[![Open In Colab](https://colab.research.google.com/assets/colab-badge.svg)](https://colab.research.google.com/github/Winfredy/SadTalker/blob/main/quick_demo.ipynb)

### SadTalker：Learning Realistic 3D Motion Coefficients for Stylized Audio-Driven Single Image Talking Face Animation

[arxiv](https://arxiv.org/abs/2211.12194) | [project](https://sadtalker.github.io) | [Github](https://github.com/Winfredy/SadTalker)

Wenxuan Zhang, Xiaodong Cun, Xuan Wang, Yong Zhang, Xi Shen, Yu Guo, Ying Shan, Fei Wang.

Xi'an Jiaotong University, Tencent AI Lab, Ant Group

CVPR 2023

TL;DR: A realistic and stylized talking head video generation method from a single image and audio


Installation (around 5 mins)

In [2]:
### make sure that CUDA is available in Edit -> Nootbook settings -> GPU
!nvidia-smi --query-gpu=name,memory.total,memory.free --format=csv,noheader

Tesla T4, 15360 MiB, 14913 MiB


In [3]:
# Isolated SadTalker environment for current Colab
import subprocess, pathlib
def run(args):
    subprocess.run(args, check=True)
run(['pip', 'install', '-q', 'uv'])
run(['uv', 'python', 'install', '3.10'])
run(['uv', 'venv', '--python', '3.10', '/content/sadtalker-env'])
if not pathlib.Path('/content/SadTalker/inference.py').exists():
    run(['git', 'clone', '--depth', '1', 'https://github.com/OpenTalker/SadTalker.git', '/content/SadTalker'])
run(['uv', 'pip', 'install', '--python', '/content/sadtalker-env/bin/python', 'pip', 'setuptools<70', 'wheel'])
run(['uv', 'pip', 'install', '--python', '/content/sadtalker-env/bin/python', 'torch==2.0.1', 'torchvision==0.15.2', 'torchaudio==2.0.2'])
req = pathlib.Path('/content/SadTalker/requirements.txt').read_text()
req = '\n'.join(line for line in req.splitlines() if line.strip() not in ['gradio', 'av'])
pathlib.Path('/content/SadTalker/requirements-colab.txt').write_text(req)
run(['uv', 'pip', 'install', '--python', '/content/sadtalker-env/bin/python', '-r', '/content/SadTalker/requirements-colab.txt', 'av==12.3.0'])
run(['/content/sadtalker-env/bin/python', '-c', 'import torch, face_alignment, gfpgan; print("READY", torch.cuda.is_available())'])
print('INSTALLATION READY')

CalledProcessError: Command '['/content/sadtalker-env/bin/python', '-c', 'import torch, face_alignment, gfpgan; print("READY", torch.cuda.is_available())']' returned non-zero exit status 1.

Download models (1 mins)

In [5]:
import subprocess, os
sad_env = dict(os.environ, MPLBACKEND='Agg')
r = subprocess.run(['/content/sadtalker-env/bin/python', '-c', 'import torch, face_alignment, gfpgan; print("READY", torch.cuda.is_available())'], env=sad_env, capture_output=True, text=True)
print(r.stdout, r.stderr)
r.check_returncode()
r = subprocess.run(['bash', 'scripts/download_models.sh'], cwd='/content/SadTalker', env=sad_env, capture_output=True, text=True)
print(r.stdout[-5000:], r.stderr[-5000:])
r.check_returncode()
print('MODELS READY')

READY True
 /content/sadtalker-env/lib/python3.10/site-packages/torchvision/transforms/functional_tensor.py:5: UserWarning: The torchvision.transforms.functional_tensor module is deprecated in 0.15 and will be **removed in 0.17**. Please don't rely on it. You probably just need to use APIs in torchvision.transforms.functional or in torchvision.transforms.v2.functional.
  warnings.warn(

 ........ .......... 96%  326M 0s
 80150K .......... .......... .......... .......... .......... 96%  291M 0s
 80200K .......... .......... .......... .......... .......... 96%  335M 0s
 80250K .......... .......... .......... .......... .......... 96%  372M 0s
 80300K .......... .......... .......... .......... .......... 96%  281M 0s
 80350K .......... .......... .......... .......... .......... 96%  226M 0s
 80400K .......... .......... .......... .......... .......... 96%  403M 0s
 80450K .......... .......... .......... .......... .......... 96% 13.7M 0s
 80500K .......... .......... .......... ...

In [6]:
from google.colab import files
from pathlib import Path
import os
os.chdir('/content/SadTalker')
print('Select your portrait image and voice-over audio together')
uploaded = files.upload()
image_ext = {'.png', '.jpg', '.jpeg', '.webp'}
audio_ext = {'.wav', '.mp3', '.m4a', '.ogg', '.flac', '.aac'}
images = [name for name in uploaded if Path(name).suffix.lower() in image_ext]
audios = [name for name in uploaded if Path(name).suffix.lower() in audio_ext]
assert len(images) == 1 and len(audios) == 1, 'Upload exactly one image and one audio file'
source_image = str(Path(images[0]).resolve())
driven_audio = str(Path(audios[0]).resolve())
print('FILES READY:', images[0], audios[0])

Select your portrait image and voice-over audio together


Saving Warm Café Portrait in a Mauve Hijab.png to Warm Café Portrait in a Mauve Hijab.png
Saving ElevenLabs_2026-10-03T21_14_52_Sara - Soft, Calm and Gentle_pvc_sp100_s50_sb56_v3.mp3 to ElevenLabs_2026-10-03T21_14_52_Sara - Soft, Calm and Gentle_pvc_sp100_s50_sb56_v3.mp3
FILES READY: Warm Café Portrait in a Mauve Hijab.png ElevenLabs_2026-10-03T21_14_52_Sara - Soft, Calm and Gentle_pvc_sp100_s50_sb56_v3.mp3


Animation

In [7]:
import subprocess, os
from pathlib import Path
sad_env = dict(os.environ, MPLBACKEND='Agg')
cmd = ['/content/sadtalker-env/bin/python', 'inference.py', '--driven_audio', driven_audio, '--source_image', source_image, '--result_dir', '/content/SadTalker/results', '--still', '--preprocess', 'full', '--enhancer', 'gfpgan']
print('Generating your video...', flush=True)
with open('/content/SadTalker/generation.log', 'w') as log:
    result = subprocess.run(cmd, cwd='/content/SadTalker', env=sad_env, stdout=log, stderr=subprocess.STDOUT)
print(Path('/content/SadTalker/generation.log').read_text()[-10000:])
result.check_returncode()
print('VIDEO READY')

Generating your video...
.19s/it]
Face Enhancer:: 100%|██████████| 894/894 [19:30<00:00,  1.31s/it]
The generated video is named /content/SadTalker/results/2026_10_03_21.41.13/Warm Café Portrait in a Mauve Hijab##ElevenLabs_2026-10-03T21_14_52_Sara - Soft, Calm and Gentle_pvc_sp100_s50_sb56_v3_enhanced.mp4
The generated video is named: /content/SadTalker/results/2026_10_03_21.41.13.mp4

VIDEO READY


In [8]:
from pathlib import Path
from IPython.display import Video, display
from google.colab import files
import subprocess, json, shutil
outputs = sorted(Path('/content/SadTalker/results').glob('*.mp4'), key=lambda p: p.stat().st_mtime)
assert outputs, 'No completed video found yet'
final_video = outputs[-1]
probe = subprocess.run(['ffprobe', '-v', 'error', '-show_entries', 'format=duration:stream=codec_type,width,height', '-of', 'json', str(final_video)], capture_output=True, text=True, check=True)
print('VIDEO DETAILS:', probe.stdout)
download_path = '/content/lip_sync_video.mp4'
shutil.copy2(final_video, download_path)
display(Video(download_path, embed=True, width=640))
files.download(download_path)
print('Download requested: lip_sync_video.mp4')

VIDEO DETAILS: {
    "programs": [

    ],
    "streams": [
        {
            "codec_type": "video",
            "width": 1888,
            "height": 3344
        },
        {
            "codec_type": "audio"
        }
    ],
    "format": {
        "duration": "35.760000"
    }
}



<IPython.core.display.Javascript object>

<IPython.core.display.Javascript object>

Download requested: lip_sync_video.mp4
